In [6]:
import os
import json

In [7]:
# base_dir = "responses"
# response_dirs = [path for path in list(os.walk(base_dir)) if len(path[0].split("/")) == 4]

# responses = {}
# for path, _, files in response_dirs:
#     _, model, prompt, seed_dir = path.split("/")
#     # print(model, prompt, seed_dir)
#     seed = seed_dir[4:]
#     # print(seed)

#     file_list = []

#     for file in files:
#         with open(f"{path}/{file}", "r") as f:
#             file_json = json.load(f)
#             file_list.append(file_json)

# print(responses)


def load_responses(model, prompt, seed):

    response_dir = f"responses/{model}/{prompt}/seed{seed}"
    file_list = []
    for _, _, files in os.walk(response_dir):
        

        for file in files:
            with open(f"{response_dir}/{file}", "r") as f:
                file_json = json.load(f)
                file_list.append(file_json)

    return file_list



In [37]:
# from collections import Counter
# answers = [r["response"] for r in responses] # if r["nli_label"] != "NotMentioned"]
# def remove_non_unique(strings):
#     counts = Counter(strings)
#     return [s for s in strings if counts[s] == 1]

# unique_answers = remove_non_unique(answers)

In [9]:
def load_response_dict(model, prompt, seed):

    response_dir = f"responses/temp0/{model}/{prompt}/seed{seed}"
    for _, _, files in os.walk(response_dir):
        file_dict = {}
        
        for file in files:
            fpath = f"{response_dir}/{file}"
            with open(fpath, "r") as f:
                file_json = json.load(f)
                file_dict[fpath] = file_json

    return file_dict

In [10]:
responses = load_response_dict("qwen3_30b", "narendra_nli", 1)
print(responses)

{'responses/temp0/qwen3_30b/narendra_nli/seed1/response_606_nda-20.json': {'document_id': 606, 'hypothesis_id': 'nda-20', 'response': '<think>\nWe are given a document (a non-disclosure agreement) and a hypothesis: "Receiving Party may retain some Confidential Information even after the return or destruction of Confidential Information."\n\nWe need to check if the document entails (supports) the hypothesis or contradicts it.\n\nLet\'s look for relevant sections in the document that discuss what happens after the return or destruction of Confidential Information.\n\nSection 9 (which is about the return or destruction of Confidential Information) states:\n\n"9. ... the parties agree that until one (1) year after the date of termination of this Agreement, neither party nor any of each party’s affiliates or its Representatives acting on the party’s behalf will, unless specifically invited in writing by the other party’s Board of Directors or its duly authorized representative: ..."\n\nWait

In [11]:
for k,v in responses.items():
    print(v.keys())
    break

dict_keys(['document_id', 'hypothesis_id', 'response', 'prediction', 'thinking', 'nli_label', 'prediction_evidence', 'annotated_spans', 'model', 'options', 'prompt', 'binary'])


In [13]:
import re
def remove_between(text: str, start_phrase: str, end_phrase: str) -> str:
    """
    Removes everything between (and including) start_phrase and end_phrase
    from the given text. If the phrases are not found, returns the text unchanged.
    """
    pattern = re.escape(start_phrase) + ".*?" + re.escape(end_phrase)
    return re.sub(pattern, "", text, flags=re.DOTALL)

b_dict = {}
n_dict = {}

def check_word(word: str, s: str):
    w_lower = word.lower()
    s_lower = s.lower()
    return w_lower in s_lower

for k,v in responses.items():
    response = v['response']
    clean_response = remove_between(response, "<think>", "</think>")
    
    contradiction = check_word("contradiction", clean_response)
    entailment = check_word("entailment", clean_response)

    if contradiction and entailment:
        b_dict[k] = clean_response
    elif contradiction:
        responses[k]["prediction"] = "Contradiction"
    elif entailment:
        responses[k]["prediction"] = "Entailment"
    else:
        n_dict[k] = clean_response

print(f"""
         Both: {len(b_dict)}
      Neither: {len(n_dict)}
       Single: {len(responses) - len(b_dict) - len(n_dict)}
""")


         Both: 68
      Neither: 37
       Single: 1083



In [34]:
false_e = {}
false_c = {}
true_e = {}
true_c = {}

def str_match(str1: str, str2: str):
    return str1.lower() == str2.lower()

correct_responses = 0
for k,v in responses.items():
    
    if v["prediction"] is None:
        continue
    correct_responses += 1

    prediction = v["prediction"].lower()
    label = v["nli_label"].lower()
    match prediction:
        case "entailment":
            if prediction == label:
                true_e[k] = v
            else:
                false_e[k] = v
        
        case "contradiction":
            if prediction == label:
                true_c[k] = v
            else:
                false_c[k] = v

print(correct_responses)

1083


In [36]:
l = [[len(true_e), len(true_c)],
     [len(false_e), len(false_c)]]

for x,y in l:
    print("{:<3} {:<6}".format(x,y))

print("=======")

for row in l:
    percent = [round(r / correct_responses, 3) for r in row]
    x,y = percent
    print("{:<3} {:<6}".format(x,y))

821 172   
39  51    
0.758 0.159 
0.036 0.047 
